# 双向采样的合约价格与结果展示

本 Notebook 定义各合约价格的生成方法：共用采样位置和分钟内比例，使用各合约自己的 open、close 返回普通价格。价格函数可以直接接收位置，也可以与第一本的位置函数串联，从指定分界 $t$ 分批生成固定或滚动分界的结果。

## 目录

- [共用采样位置，各合约生成自己的价格](#contract-sampling-prices)
- [输入选择与结果保存](#input-and-saving)
- [固定分界的完整序列 demo](#fixed-boundary-demo)
- [逐分钟滚动分界 demo](#rolling-boundary-demo)
- [48 组价格数据 demo](#saved-价格-demos)
- [主力价格序列与 GH 拟合](#main-price-and-gh)
- [单图交互选择](#interactive-image-comparison)

输入是[主力连续复权 Notebook](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b02_MainContinuousAdjustment/c01_MainContinuousAdjustment.ipynb)生成的同品种全部合约分钟数据。分钟末端字段为 `bar_at`，交易日字段为 `trading_date`，价格使用复权后的 OHLC。输入按初始训练／测试范围完成复权：训练期双向复权；测试期以第一个实际主力分钟为固定起点，只累计测试期内部后续换约的偏移。采样分界移动时，使用这份固定输入。

[采样位置 Notebook](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c01_SamplingPositions.ipynb)定义实际分钟、成交额与 GK×成交额三条轴、初始单位 $a$ 以及双向位置。$a$ 由初始训练期平均每分钟增量乘候选分钟数 $N$ 得到，校准后固定；$t$ 是已知 close 的训练末端，过去序列最后保留该 close，未来从下一实际分钟开始。每侧最多返回 $K$ 点，不足返回实际点数；单分界的 `K=None` 返回完整序列。

执行顺序为准备分钟轴与合约报价、确定单位和位置、生成价格、保存，再读取主力采样序列绘图。每次通过参数选择一个业务配置。下方演示固定和滚动分界，列出 48 组独立生成的数据，通过单图交互选择呈现全部配置的图像。


In [ ]:
import pathlib
import sys

# 定位项目根并启用仓库配置、研究方法的正常导入。
project_markers = ['.git', '.env', 'config/settings.py']
current_path = pathlib.Path.cwd()
for candidate_root in [current_path, *current_path.parents]:
    if all(((candidate_root / marker).exists() for marker in project_markers)):
        sys.path.insert(0, str(candidate_root))
        from config.settings import settings
        break
else:
    raise RuntimeError('无法定位项目根，请在包含 .git、.env、config/settings.py 的项目中运行')

In [ ]:
from __future__ import annotations

from datetime import date, datetime, timezone
from pathlib import Path
import base64
import hashlib
import json
import os
import platform
import sys
import numba
import numpy as np
import pandas as pd
import pyarrow as pa
import pyarrow.parquet as pq
from numba import njit, prange
from config.data_contracts import FUTURES_MINUTE_SCHEMA
from R04_Research.a01_Methods.b02_MainContinuousAdjustment.c01_MainContinuousAdjustment import (
    MAIN_CONTINUOUS_ADJUSTMENT_VERSION, ALL_CONTRACT_ADJUSTED_MINUTE_SCHEMA,
    ArrowContentDigest, arrow_content_sha256,
)
from R04_Research.a01_Methods.b03_Sampling.c01_SamplingPositions import (
    SAMPLING_POSITIONS_VERSION, SAMPLING_POSITION_SCHEMA, POSITION_COLUMN_LABELS, prepare_sampling_axis,
    SAMPLING_TIMEZONE, SAMPLING_INPUT_COLUMNS, generate_sampling_column, calibrate_sampling_unit,
    generate_sampling_positions, iter_sampling_position_batches,
)

SAMPLING_EXECUTION_VERSION = '0.1.0'

# 保留采样位置并展开源分钟的真实合约，价格使用普通数值。
SAMPLED_CLOSE_SCHEMA = pa.schema([
    *SAMPLING_POSITION_SCHEMA,  # 沿用共同位置、分界和采样序号
    FUTURES_MINUTE_SCHEMA.field('exchange_code'), FUTURES_MINUTE_SCHEMA.field('underlying_code'),
    FUTURES_MINUTE_SCHEMA.field('contract_code'), pa.field('is_main', pa.bool_(), nullable=False),
    pa.field('sampled_close', pa.float64()),  # 允许缺价；log 插值后还原的价格
], metadata={b'method_name': b'sampling_execution', b'method_version': SAMPLING_EXECUTION_VERSION.encode(),
             b'timezone': SAMPLING_TIMEZONE.encode(), b'primary_key': b'sample_id,contract_code',
             b'price_domain': b'ordinary price; linear interpolation in log open/close',
             b'grain_zh': '每个采样点的每个源分钟有记录的真实合约一行'.encode()})


In [ ]:
# 中文名称只用于表格展示副本，不改写计算字段或文件。
EXECUTION_COLUMN_LABELS = {**POSITION_COLUMN_LABELS,
    'is_main': 'is_main（是否当分钟主力）', 'sampled_close': 'sampled_close（采样收盘价格）',
    'log_return': 'log_return（相邻采样点对数收益率）', 'a': 'a（固定采样单位）',
    'N': 'N（候选分钟单位）', 'training_minutes': 'training_minutes（校准训练实际分钟数）',
    'training_total_increment': 'training_total_increment（校准训练增量合计）',
    'training_start_date': 'training_start_date（校准训练首交易日）',
    'training_end_date': 'training_end_date（校准训练末交易日）',
    'test_start_date': 'test_start_date（初始测试交易日分界）',
}



In [ ]:
# 展示本 Notebook 输出字段、类型及空值约束。
display(pd.DataFrame([{'数据结构': name, '字段': EXECUTION_COLUMN_LABELS[field.name], 'Arrow 类型': str(field.type), '允许空值': field.nullable}
                      for name, schema in (('sampled_close', SAMPLED_CLOSE_SCHEMA),) for field in schema]))



## 共用采样位置，各合约生成自己的价格

<a id="contract-sampling-prices"></a>

`prepare_sampling_input` 读取复权分钟数据，返回分钟轴和合约报价；`prepare_contract_quotes` 按实际源分钟保存合约报价，并预先计算 log open 与 log close，供多个分界复用。

同一采样点的所有合约共用源分钟和插值比例 $\theta$。对于源分钟 $i$ 的合约 $c$，分钟内插值价格为

$$P_{i,c}(\theta)=\exp\left[(1-\theta)\ln O_{i,c}+\theta\ln C_{i,c}\right].$$

$O_{i,c}$、$C_{i,c}$ 是该合约自己的复权 open、close，返回的 `sampled_close` 为普通价格。比例恰好为 1 时直接返回 close；分钟末清零方式的所有采样点均使用这一末端价格。

分钟内插值要求 open、close 都有限且为正；精确末端只要求 close 有效。报价缺失或无效时，保留已有合约行，将采样价格置空，不前填、不后填。源分钟完全没有该合约记录时，输出不新增该合约行；采样位置表仍保留这个点，缺价格不改变点数。

已有位置可交给 `sample_all_contract_prices` 生成全部合约价格。`iter_sampled_price_batches` 接收准备好的报价、轴、$t$ 与 $K$，将位置生成和价格生成串联并分批返回；传入单个 $t$ 执行固定分界，传入递增 $t$ 序列执行滚动分界。批次可以直接交给保存函数消费。


In [ ]:
def prepare_contract_quotes(adjusted_minute_df, axis_minute_df: pd.DataFrame) -> dict:
    """按源分钟准备稀疏报价索引和 log 价格，滚动时不重复连接或取对数。"""

    # 按实际源分钟排列真实合约报价，保留稀疏行结构。
    names = ['exchange_code', 'underlying_code', 'contract_code', 'bar_at', 'is_main', 'adjusted_open', 'adjusted_close']
    quotes = (adjusted_minute_df.select(names) if isinstance(adjusted_minute_df, pa.Table)
              else pa.Table.from_pandas(adjusted_minute_df[names], preserve_index=False))
    quotes = quotes.sort_by([('bar_at', 'ascending'), ('contract_code', 'ascending')]).combine_chunks()
    times = pd.DatetimeIndex(axis_minute_df['bar_at'])
    minute_indices = times.get_indexer(pd.DatetimeIndex(quotes['bar_at'].to_pandas()))
    if (minute_indices < 0).any():
        raise ValueError('报价源分钟不在已准备的采样轴中')

    # 为每分钟建立连续报价区间，采样时直接按偏移取行。
    counts = np.bincount(minute_indices, minlength=len(times))
    offsets = np.r_[0, np.cumsum(counts)].astype(np.int64)  # 第 i 分钟的报价为 offsets[i]:offsets[i+1]
    opening = quotes['adjusted_open'].to_numpy().astype(float)
    closing = quotes['adjusted_close'].to_numpy().astype(float)

    # 无效 close 置空；分钟内插值还需要有效 open。
    valid_close = np.isfinite(closing) & (closing > 0)
    closing = np.where(valid_close, closing, np.nan)
    valid_inside = valid_close & np.isfinite(opening) & (opening > 0)
    log_opening = np.full(len(opening), np.nan)
    log_difference = np.full(len(opening), np.nan)
    log_opening[valid_inside] = np.log(opening[valid_inside])
    log_difference[valid_inside] = np.log(closing[valid_inside]) - log_opening[valid_inside]  # 预先计算 log close − log open

    # 合约标识做字典编码，减少滚动展开时的重复字符串。
    identifiers = quotes.select(['exchange_code', 'underlying_code', 'contract_code', 'is_main'])
    for name in ('exchange_code', 'underlying_code', 'contract_code'):
        identifiers = identifiers.set_column(identifiers.schema.get_field_index(name), name,
                                            identifiers[name].combine_chunks().dictionary_encode())
    return dict(identifiers=identifiers, offsets=offsets, closing=closing,
                log_opening=log_opening, log_difference=log_difference)


@njit(cache=False, parallel=True)
def _sample_prices(minute_indices, fractions, offsets, closing, log_opening, log_difference):

    # 先确定每点要展开几行报价，再一次分配输出数组。
    sample_offsets = np.empty(len(minute_indices) + 1, dtype=np.int64)
    sample_offsets[0] = 0
    for point in range(len(minute_indices)):
        minute = minute_indices[point]
        sample_offsets[point + 1] = sample_offsets[point] + offsets[minute + 1] - offsets[minute]
    point_indices = np.empty(sample_offsets[-1], dtype=np.int64)
    quote_indices = np.empty(sample_offsets[-1], dtype=np.int64)
    prices = np.empty(sample_offsets[-1])

    # 各点写入互不重叠的区间；所有合约共用该点比例。
    for point in prange(len(minute_indices)):
        minute = minute_indices[point]
        fraction = fractions[point]
        for quote in range(offsets[minute], offsets[minute + 1]):
            output_row = sample_offsets[point] + quote - offsets[minute]
            point_indices[output_row] = point  # 对应哪一个采样位置
            quote_indices[output_row] = quote  # 对应哪一行合约报价

            # 恰好落在末端直接取 close；其他比例在 log 价格中线性插值。
            prices[output_row] = (closing[quote] if fraction == 1.0 else
                                 np.exp(log_opening[quote] + fraction * log_difference[quote]))
    return point_indices, quote_indices, prices


def sample_all_contract_prices(prepared_quotes: dict, sample_position_df: pd.DataFrame) -> pd.DataFrame:
    """所有合约共用位置；各自 log open/close 插值后返回普通价格。"""

    # 按位置展开全部合约；缺价格保留 NaN，占用采样点数。
    indices = sample_position_df['source_minute_index'].to_numpy(dtype=np.int64)
    fractions = sample_position_df['interpolation_fraction'].to_numpy(dtype=float)
    point_rows, quote_rows, prices = _sample_prices(
        indices, fractions, prepared_quotes['offsets'], prepared_quotes['closing'],
        prepared_quotes['log_opening'], prepared_quotes['log_difference'])
    if (~np.isnan(prices) & (~np.isfinite(prices) | (prices <= 0))).any():
        raise ValueError('采样价格数值溢出或无效')

    # 将公共位置复制到合约行，附上标识和普通价格。
    points = pa.Table.from_pandas(sample_position_df, schema=SAMPLING_POSITION_SCHEMA, preserve_index=False).take(pa.array(point_rows))
    identifiers = prepared_quotes['identifiers'].take(pa.array(quote_rows))
    for name in identifiers.column_names:
        points = points.append_column(name, identifiers[name])
    points = points.append_column('sampled_close', pa.array(prices, from_pandas=True))  # NaN 按 Arrow 空值写入
    return points.cast(SAMPLED_CLOSE_SCHEMA).to_pandas(types_mapper=pd.ArrowDtype)


def prepare_sampling_input(demo_path: str | Path, *, axis: str, quantity_scope: str = 'all_contracts'):
    """b02 读一遍，准备实际分钟轴与可复用的稀疏合约报价。"""
    axis_parts, quote_parts = [], []

    # 输入只读一遍，同时收集分钟轴与报价所需字段。
    for minute_batch in iter_adjusted_minute_batches(demo_path):
        axis_parts.append(generate_sampling_column(minute_batch, axis=axis, quantity_scope=quantity_scope))
        quote_parts.append(pa.Table.from_pandas(minute_batch[
            ['exchange_code', 'underlying_code', 'contract_code', 'bar_at', 'is_main', 'adjusted_open', 'adjusted_close']],
            preserve_index=False))
    if not axis_parts:
        raise ValueError('输入没有实际分钟')

    # 合并实际分钟并一次建立报价索引，供后续 t 复用。
    axis_minutes = pd.concat(axis_parts, ignore_index=True)
    prepared_quotes = prepare_contract_quotes(pa.concat_tables(quote_parts), axis_minutes)
    return axis_minutes, prepared_quotes


def iter_sampled_price_batches(prepared_quotes: dict, prepared_axis: dict, *, t, K: int | None = None,
                              batch_size: int = 512):
    """固定分界或给定滚动分界序列；分批生成，避免保留所有 t 的展开价格。"""
    if isinstance(batch_size, bool) or not isinstance(batch_size, (int, np.integer)) or batch_size <= 0:
        raise ValueError('batch_size 必须是正整数')
    scalar_t = isinstance(t, (str, datetime)) or np.isscalar(t)  # 区分一个分界与分界序列

    # 单个 t 先生成位置，再按点数分批展开价格。
    if scalar_t:
        positions = generate_sampling_positions(prepared_axis, t=t, K=K)
        for first in range(0, len(positions), batch_size):
            yield sample_all_contract_prices(prepared_quotes, positions.iloc[first:first + batch_size])
    else:

        # 滚动 t 必须限制每侧点数；位置和价格均逐批消费。
        if K is None:
            raise ValueError('滚动采样必须指定 K')
        for positions in iter_sampling_position_batches(prepared_axis, t=t, K=K, batch_size=batch_size):
            yield sample_all_contract_prices(prepared_quotes, positions)


def build_main_sample_series(sample_position_df: pd.DataFrame, sampled_price_df: pd.DataFrame) -> pd.DataFrame:
    """每个 t 的过去与未来连成一个序列后计算 log 差分，保留缺价格。"""

    # 按位置左连接主力报价，保留缺价点及相邻关系。
    main_prices = sampled_price_df.loc[sampled_price_df['is_main'], ['sample_id', 'sampled_close']]
    result = (
        sample_position_df.merge(main_prices, on='sample_id', how='left', validate='one_to_one')
        .sort_values('sample_id').reset_index(drop=True)
    )
    prices = result['sampled_close'].to_numpy(dtype=float, na_value=np.nan)

    # 同一 t 内训练、测试连成一个序列后差分；不同 t 的窗口彼此独立。
    result['log_return'] = pd.Series(np.log(prices)).groupby(result['t'], sort=False).diff()  # 不按 sample_side 拆开差分
    return result


## 输入选择与结果保存

<a id="input-and-saving"></a>

复权输入由完整文件名显式选择。`verify_adjusted_demo` 核对品种、训练／测试范围、生成定义及内容摘要，确保输入与所选配置一致；不匹配时明确报错，提示重新计算。

位置和价格分别保存为 Parquet：位置表每个采样点一行，价格表每个采样点在源分钟有记录的真实合约一行。两者共用 `sample_id` 关联，分别使用 `SAMPLING_POSITION_SCHEMA` 与 `SAMPLED_CLOSE_SCHEMA`。表格预览中的中文表头只用于展示，文件保留原英文字段。

`sampling_demo_identity` 记录上游身份、参数、校准范围、两本采样 Notebook 的生成定义及运行环境；保存时补充输出行数与内容摘要，一并写入文件 metadata。纯绘图定义不参与数据身份。`save_sampling_demo` 写入后复读验收，已有文件的身份与内容一致时保留其字节和生成时间。文件名用于选择配置，metadata 用于核对该配置的实际生成条件。


In [ ]:
def iter_adjusted_minute_batches(demo_path: str | Path, *, batch_size: int = 131072):
    """按上游已声明的时间顺序读取，保留批次尾分钟到下一批。"""
    pending_minute_table = None

    # 按文件批次读取；将上批尚未读完的最后一分钟接到本批。
    for minute_batch in pq.ParquetFile(demo_path).iter_batches(batch_size=batch_size, columns=SAMPLING_INPUT_COLUMNS):
        minute_table = pa.Table.from_batches([minute_batch])
        if pending_minute_table is not None:
            minute_table = pa.concat_tables([pending_minute_table, minute_table])

        # 暂留尾分钟，避免同一分钟的合约被拆成两次成交额合计。
        last_bar_at = minute_table['bar_at'][-1].as_py()
        import pyarrow.compute as pc
        tail_minute_mask = pc.equal(minute_table['bar_at'], pa.scalar(last_bar_at, type=minute_table['bar_at'].type))
        complete_minute_table = minute_table.filter(pc.invert(tail_minute_mask))
        pending_minute_table = minute_table.filter(tail_minute_mask)
        if complete_minute_table.num_rows:
            yield complete_minute_table.to_pandas(types_mapper=pd.ArrowDtype)

    # 文件结束后输出最后一个完整分钟。
    if pending_minute_table is not None and pending_minute_table.num_rows:
        yield pending_minute_table.to_pandas(types_mapper=pd.ArrowDtype)

def verify_adjusted_demo(demo_path: str | Path, *, producer_notebook: str | Path, project_root: str | Path,
                         underlying_code: str, test_start_date: str | date) -> dict:
    """读取前核对 b02 条件与实际内容；不重复上游业务验收。"""
    root = Path(project_root).resolve()
    notebook_path = Path(producer_notebook).resolve()
    schema = pq.read_schema(demo_path)
    identity = json.loads((schema.metadata or {})[b'demo_identity'])

    # 核对上游品种、复权口径及训练／测试分界。
    expected = {
        'artifact_role': 'method_demo', 'method_version': MAIN_CONTINUOUS_ADJUSTMENT_VERSION,
        'producer_notebook': notebook_path.relative_to(root).as_posix(),
        'underlying_code': underlying_code, 'timezone': SAMPLING_TIMEZONE,
    }
    for key, value in expected.items():
        if identity.get(key) != value:
            raise RuntimeError(f'b02 生成身份 {key} 不匹配，请先重算对应 demo')
    if identity['parameters'].get('test_start_date') != pd.Timestamp(test_start_date).date().isoformat():
        raise RuntimeError('b02 训练／测试分界不匹配，请先重算对应 demo')

    # 确认实际依赖的生成代码与保存身份一致。
    notebook = json.loads(notebook_path.read_text(encoding='utf8'))
    source = '\n\n'.join(
        (''.join(c['source']) for c in notebook['cells']
         if c['cell_type'] == 'code' and {'export', 'demo-dependency'}.issubset(c.get('metadata', {}).get('tags', [])))
    )
    if hashlib.sha256(source.encode()).hexdigest() != identity['method_source_sha256']:
        raise RuntimeError('b02 生成定义已变化，请先重算对应 demo')
    dependencies = {'notebook_loader': root / 'R04_Research/a00_notebook_loader.py', 'data_contracts': root / 'config/data_contracts.py'}
    for key, path in dependencies.items():
        if hashlib.sha256(path.read_bytes()).hexdigest() != identity['dependency_source_sha256'][key]:
            raise RuntimeError(f'b02 依赖 {key} 已变化，请先重算对应 demo')

    # 核对文件内容摘要，不重做上游主力识别或复权业务校验。
    actual = arrow_content_sha256(demo_path, ALL_CONTRACT_ADJUSTED_MINUTE_SCHEMA, identity['output_sort_keys'])
    if actual != identity['output_content_sha256']:
        raise RuntimeError('b02 实际内容与其生成身份不一致')
    return identity

def save_sampling_demo(sampled_batches, *, demo_path: str | Path, demo_identity: dict, schema: pa.Schema = SAMPLED_CLOSE_SCHEMA) -> dict:
    """保存单个配置的全合约采样长表，复读验收后原子安装。"""
    sampling_demo_path = Path(demo_path)
    sampling_demo_path.parent.mkdir(parents=True, exist_ok=True)
    sampled_schema = schema
    sort_keys = [('sample_id', 'ascending')] + ([('contract_code', 'ascending')] if 'contract_code' in schema.names else [])  # 位置按采样编号；价格再按合约编号

    # 先写同目录 staging；发现遗留文件时保留现场并停止。
    staged_path = sampling_demo_path.with_name(sampling_demo_path.name + '.staging')
    if staged_path.exists():
        raise RuntimeError(f'存在未处理 staging，请先核查：{staged_path}')
    sampled_price_batches = [sampled_batches] if isinstance(sampled_batches, pd.DataFrame) else sampled_batches
    digest = ArrowContentDigest(sampled_schema)
    output_rows = 0
    previous_id = 0

    # 逐批排序、检查必填字段并累计内容摘要，写入 staging。
    with pq.ParquetWriter(staged_path, sampled_schema, compression='zstd', compression_level=7) as writer:
        for sampled_price_df in sampled_price_batches:
            sampled_price_table = (
                pa.Table.from_pandas(sampled_price_df, schema=sampled_schema, preserve_index=False)
                .replace_schema_metadata(sampled_schema.metadata).sort_by(sort_keys)
            )
            if not sampled_price_table.num_rows:
                continue
            if sampled_price_table['sample_id'][0].as_py() <= previous_id:
                raise ValueError('采样保存批次编号重叠或逆序')
            previous_id = sampled_price_table['sample_id'][-1].as_py()  # 下一批不得重叠或逆序
            for field in sampled_schema:
                if not field.nullable and sampled_price_table[field.name].null_count:
                    raise ValueError(f'采样输出强制字段 {field.name} 出现空值')
            digest.update(sampled_price_table)
            output_rows += sampled_price_table.num_rows
            writer.write_table(sampled_price_table, row_group_size=131072)

        # 将输出行数、Schema 和内容摘要写入文件自身的生成身份。
        expected_identity = json.loads(json.dumps({
            **demo_identity, 'output_rows': output_rows, 'output_sort_keys': sort_keys,
            'output_schema_sha256': hashlib.sha256(sampled_schema.serialize().to_pybytes()).hexdigest(),
            'output_content_sha256': digest.hexdigest(),
        }, ensure_ascii=False, allow_nan=False))
        installed_identity = {**expected_identity, 'generated_at_utc': datetime.now(timezone.utc).isoformat()}
        metadata = {**sampled_schema.metadata, b'demo_identity': json.dumps(installed_identity, ensure_ascii=False, allow_nan=False, sort_keys=True).encode()}
        writer.add_key_value_metadata({**metadata, b'ARROW:schema': base64.b64encode(sampled_schema.with_metadata(metadata).serialize().to_pybytes())})

    # 复读 staging 后再比较已安装文件；身份和数据都一致则保留已有字节。
    if arrow_content_sha256(staged_path, sampled_schema, sort_keys) != expected_identity['output_content_sha256']:
        raise RuntimeError('采样 staging 内容摘要不一致，保留现场')
    preserved = False
    if sampling_demo_path.exists():
        existing_schema = pq.read_schema(sampling_demo_path)
        existing_identity = json.loads(existing_schema.metadata[b'demo_identity'])
        existing_base_schema = existing_schema.with_metadata({k: v for k, v in existing_schema.metadata.items() if k != b'demo_identity'})
        if arrow_content_sha256(sampling_demo_path, existing_base_schema, existing_identity['output_sort_keys']) != existing_identity['output_content_sha256']:
            raise RuntimeError('已有采样 demo 与自身内容摘要不一致')
        if (existing_base_schema.equals(sampled_schema, check_metadata=True)
                and {k: v for k, v in existing_identity.items() if k != 'generated_at_utc'} == expected_identity):
            preserved = True
            installed_identity = existing_identity
            staged_path.unlink()  # 已有产物完全一致，删除本次临时文件

    # 需要更新时原子安装，随后再次核对 Schema、身份和内容。
    if not preserved:
        os.replace(staged_path, sampling_demo_path)  # 验收通过后替换正式 demo
    installed_schema = pq.read_schema(sampling_demo_path)
    existing_base_schema = installed_schema.with_metadata({k: v for k, v in installed_schema.metadata.items() if k != b'demo_identity'})
    if not existing_base_schema.equals(sampled_schema, check_metadata=True) or json.loads(installed_schema.metadata[b'demo_identity']) != installed_identity:
        raise RuntimeError('安装后采样 Schema 或生成身份不一致')
    if arrow_content_sha256(sampling_demo_path, sampled_schema, sort_keys) != expected_identity['output_content_sha256']:
        raise RuntimeError('安装后采样实际内容不一致')
    return {'identity': installed_identity, 'preserved_existing': preserved, 'file_bytes': sampling_demo_path.stat().st_size}


In [ ]:
def sampling_demo_identity(*, project_root: str | Path, producer_notebook: str | Path,
                           upstream_identity: dict, parameters: dict, calibration: dict, scope: dict) -> dict:
    """记录两个 Notebook 的生成定义、上游身份、固定校准范围与执行条件。"""
    root = Path(project_root).resolve()
    producer = Path(producer_notebook).resolve()
    sources = {}
    notebooks = {
        'sampling_positions': root / 'R04_Research/a01_Methods/b03_Sampling/c01_SamplingPositions.ipynb',
        'sampling_execution': root / 'R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution.ipynb',
    }

    # 只取生成依赖单元格，纯绘图与展示标签不参与数据摘要。
    for name, path in notebooks.items():
        notebook = json.loads(path.read_text(encoding='utf8'))
        source = '\n\n'.join(''.join(cell['source']) for cell in notebook['cells']
                             if cell['cell_type'] == 'code' and {'export', 'demo-dependency'}.issubset(cell.get('metadata', {}).get('tags', [])))
        sources[name] = hashlib.sha256(source.encode()).hexdigest()  # 代码原文摘要，包含排版与注释

    # 保存上游、校准、两本 Notebook 依赖及数值环境，供读取时核对。
    return dict(artifact_role='method_demo', producer_notebook=producer.relative_to(root).as_posix(),
                method_version={'c01_SamplingPositions': SAMPLING_POSITIONS_VERSION,
                                'c02_SamplingExecution': SAMPLING_EXECUTION_VERSION}[producer.stem],
                method_source_tag='demo-dependency',
                method_source_sha256=sources[{'c01_SamplingPositions': 'sampling_positions',
                                             'c02_SamplingExecution': 'sampling_execution'}[producer.stem]],
                dependency_method_source_sha256=sources, dependency_source_sha256={
                    'notebook_loader': hashlib.sha256((root / 'R04_Research/a00_notebook_loader.py').read_bytes()).hexdigest(),
                    'data_contracts': hashlib.sha256((root / 'config/data_contracts.py').read_bytes()).hexdigest(),
                    'main_adjustment': upstream_identity.get('method_source_sha256')},
                timezone=SAMPLING_TIMEZONE, parameters=parameters, calibration=calibration, scope=scope,
                upstream_demo_identity=upstream_identity,
                runtime=dict(python=sys.version.split()[0], numpy=np.__version__, pandas=pd.__version__,
                             pyarrow=pa.__version__, numba=numba.__version__, threads=numba.get_num_threads(),
                             platform=platform.platform()))


In [ ]:
def read_reusable_sampling_identity(demo_path: str | Path, *, project_root: str | Path,
                                   producer_notebook: str | Path, upstream_path: str | Path,
                                   underlying_code: str, test_start_date: str | date,
                                   parameters: dict, reuse_existing: bool = True) -> dict | None:
    """条件与内容匹配时返回已有身份；缺失或条件变化时返回 None，损坏文件报错。"""
    path = Path(demo_path)
    if not reuse_existing or not path.exists():
        return None
    if path.with_name(path.name + '.staging').exists():
        raise RuntimeError(f'存在未处理 staging，请先核查：{path}')
    root = Path(project_root).resolve()
    producer = Path(producer_notebook).resolve()
    schema = pq.read_schema(path)
    identity = json.loads(schema.metadata[b'demo_identity'])
    upstream = json.loads(pq.read_schema(upstream_path).metadata[b'demo_identity'])
    boundary = pd.Timestamp(test_start_date).date().isoformat()

    # 先核对品种、初始分界、请求参数与上游身份，尚未读取分钟数据。
    if (upstream['underlying_code'] != underlying_code
            or upstream['parameters'].get('test_start_date') != boundary
            or identity['calibration']['test_start_date'] != boundary
            or identity['calibration']['N'] != parameters['N']
            or any(identity['parameters'].get(key) != value for key, value in parameters.items())
            or identity['upstream_demo_identity'] != upstream
            or any(identity['scope'].get(key) != value for key, value in upstream['scope'].items())):
        return None

    # 上游代码变化后不能消费其旧产物；内容质量沿用上游已完成的验收。
    upstream_book = json.loads((root / upstream['producer_notebook']).read_text(encoding='utf8'))
    upstream_source = '\n\n'.join(''.join(cell['source']) for cell in upstream_book['cells']
        if cell['cell_type'] == 'code' and {'export', 'demo-dependency'}.issubset(cell.get('metadata', {}).get('tags', [])))
    if hashlib.sha256(upstream_source.encode()).hexdigest() != upstream['method_source_sha256']:
        raise RuntimeError('b02 生成定义已变化，请先重算对应 demo')
    for name, relative in [('notebook_loader', 'R04_Research/a00_notebook_loader.py'), ('data_contracts', 'config/data_contracts.py')]:
        if hashlib.sha256((root / relative).read_bytes()).hexdigest() != upstream['dependency_source_sha256'][name]:
            raise RuntimeError(f'b02 依赖 {name} 已变化，请先重算对应 demo')

    # 核对当前生成定义和数值环境；保存的校准值、t 和范围来自同一上游。
    current = sampling_demo_identity(project_root=root, producer_notebook=producer,
        upstream_identity=upstream, parameters=identity['parameters'],
        calibration=identity['calibration'], scope=identity['scope'])
    if any(identity.get(key) != value for key, value in current.items()):
        return None
    expected_schema = SAMPLING_POSITION_SCHEMA if producer.stem == 'c01_SamplingPositions' else SAMPLED_CLOSE_SCHEMA
    actual_schema = schema.with_metadata({key: value for key, value in schema.metadata.items() if key != b'demo_identity'})
    if not actual_schema.equals(expected_schema, check_metadata=True):
        return None
    if arrow_content_sha256(path, expected_schema, identity['output_sort_keys']) != identity['output_content_sha256']:
        raise RuntimeError('已有采样 demo 与自身内容摘要不一致，停止复用')
    return identity


In [ ]:
def plot_sampling_price_series(main_sample_df: pd.DataFrame, *, title: str | None = None,
                               figsize=(25, 6), n_ticks: int = 10, linewidth: float = 0.35):
    """按采样顺序绘制 log 主力价格，以稀疏交易日标注横轴。"""
    import matplotlib.pyplot as plt
    if main_sample_df.empty:
        raise ValueError('没有采样点，无法绘制价格序列')
    plt.rcParams['font.sans-serif'] = ['SimHei', 'Arial Unicode MS', 'DejaVu Sans']
    plt.rcParams['axes.unicode_minus'] = False

    # 按采样顺序绘制 log 主力价格，缺价保持曲线断点。
    figure, axes = plt.subplots(figsize=figsize)
    prices = main_sample_df['sampled_close'].to_numpy(dtype=float, na_value=np.nan)
    index_range = np.arange(len(main_sample_df))
    axes.plot(index_range, np.log(prices), linewidth=linewidth)  # log 价格，缺价处断开

    # 用少量交易日刻度显示整个序列的时间跨度。
    tick_positions = np.linspace(0, len(main_sample_df) - 1, min(n_ticks, len(main_sample_df)), dtype=int)
    dates = main_sample_df['trading_date'].reset_index(drop=True)
    axes.set_xticks(tick_positions)
    axes.set_xticklabels([str(dates.iloc[position])[:10] for position in tick_positions], rotation=0, ha='center')
    if len(main_sample_df) > 1:
        axes.set_xlim(index_range[0], index_range[-1])
    axes.set_ylabel('对数价格 Log Price', fontsize=12)
    if title:
        axes.set_title(title, fontsize=12, pad=10)
    return figure


def plot_sampling_gh_distribution(main_sample_df: pd.DataFrame, *, fit_generalized_hyperbolic: bool = True,
                                  bins: int = 700, figsize=(13, 3.5), dpi: int = 200,
                                  xlim=None, ylim=None, title: str | None = None,
                                  label: str = '采样颗粒度 10min'):
    """直接使用已算好的 log 收益率；白底黑边直方图与蓝色 GH 曲线。"""
    import matplotlib.pyplot as plt
    from scipy.stats import genhyperbolic

    # 收益率已由主力序列计算；这里只去除空收益率，不再次差分。
    log_returns = main_sample_df['log_return'].dropna().to_numpy(dtype=float)
    if not len(log_returns):
        raise ValueError('没有非空 log 收益率，无法绘制分布或拟合')
    gh_parameters = None

    # 对全部非空收益率拟合 GH，失败明确报错。
    if fit_generalized_hyperbolic:
        try:
            gh_parameters = genhyperbolic.fit(log_returns)  # λ、α、β、μ、δ
            grid = np.linspace(log_returns.min(), log_returns.max(), 1000)
            density = genhyperbolic.pdf(grid, *gh_parameters)
            if not np.isfinite(gh_parameters).all() or gh_parameters[-1] <= 0 or not np.isfinite(density).all():
                raise ValueError('拟合参数或密度无效')

        except Exception as error:
            raise RuntimeError('广义双曲分布拟合失败') from error

    plt.rcParams['font.sans-serif'] = ['SimHei', 'Arial Unicode MS', 'DejaVu Sans']
    plt.rcParams['axes.unicode_minus'] = False

    # 分布使用独立画布，白底黑边直方图配蓝色 GH 曲线。
    figure, axes = plt.subplots(figsize=figsize, dpi=dpi)
    axes.hist(log_returns, bins=bins, density=True, color='white', edgecolor='black', linewidth=0.25, label=label)
    if gh_parameters is not None:
        p, a, b, loc, scale = gh_parameters
        axes.plot(
            grid, density, 'b', linewidth=0.85,
            label=f'λ:{p:.3f}, α:{a:.3f}, β:{b:.3f}, μ:{loc:.3f}, δ:{scale:.3f}'
        )

    # 默认按全部收益率和密度缩放；指定范围时仅调整画布。
    if xlim is not None:
        axes.set_xlim(xlim)
    if ylim is None:
        axes.set_ylim(bottom=0)  # 保留完整峰顶，密度从零开始
    else:
        axes.set_ylim(ylim)
    axes.legend(loc='upper left')
    axes.grid(False)  # 不显示网格
    if title:
        axes.set_title(title)
    return figure, gh_parameters


In [ ]:
def read_sampling_demo_main_series(*, project_root: str | Path, underlying_code: str, N: int,
                                   axis: str, quantity_scope: str, sampling_method: str):
    """核对一个配置的数据，返回主力序列、图题及图像的数据来源身份。"""
    root = Path(project_root).resolve()
    # 完整文件名明确选择这一配置的位置、价格和 b02 输入。
    method_dir = root / 'R04_Research/a01_Methods/b03_Sampling'
    range_token = 'train20100101-20241231_test20250101-20260930'
    token = f'{underlying_code}_{range_token}_N{N}_{axis}_{quantity_scope}_{sampling_method}_fixed'
    position_path = method_dir / 'c01_SamplingPositions_DemoData' / f'c01_SamplingPositions_{token}_demo.parquet'
    price_path = method_dir / 'c02_SamplingExecution_DemoData' / f'c02_SamplingExecution_{token}_demo.parquet'
    upstream_path = (
        root / 'R04_Research/a01_Methods/b02_MainContinuousAdjustment/c01_MainContinuousAdjustment_DemoData'
        / f'c01_MainContinuousAdjustment_{underlying_code}_{range_token}_ratio1.10_log_common_demo.parquet'
    )
    upstream_identity = json.loads(pq.read_schema(upstream_path).metadata[b'demo_identity'])

    # 核对配置、上游身份、生成定义和实际内容，身份不符时要求重算。
    for path, schema in ((position_path, SAMPLING_POSITION_SCHEMA), (price_path, SAMPLED_CLOSE_SCHEMA)):
        identity = json.loads(pq.read_schema(path).metadata[b'demo_identity'])
        if identity['upstream_demo_identity'] != upstream_identity:
            raise RuntimeError('比较文件的 b02 输入身份不匹配，需要重算')
        parameters = identity['parameters']
        expected = dict(N=N, axis=axis, quantity_scope=quantity_scope,
                        sampling_method=sampling_method, execution_mode='fixed', K=None)
        if any(parameters.get(key) != value for key, value in expected.items()):
            raise RuntimeError('比较文件的配置不匹配，需要重算')
        current = sampling_demo_identity(project_root=root,
            producer_notebook=root / identity['producer_notebook'], upstream_identity=upstream_identity,
            parameters=parameters, calibration=identity['calibration'], scope=identity['scope'])
        if any(current[key] != identity[key] for key in
               ('method_source_sha256', 'dependency_method_source_sha256', 'dependency_source_sha256')):
            raise RuntimeError('比较文件的生成定义已变化，需要重算')
        if arrow_content_sha256(path, schema, identity['output_sort_keys']) != identity['output_content_sha256']:
            raise RuntimeError('比较文件的实际内容与摘要不一致')

    # 保留全部位置后连接主力价格，全局计算一次 log 差分。
    positions = pq.read_table(position_path).to_pandas(types_mapper=pd.ArrowDtype)
    prices = pq.read_table(price_path, filters=[('is_main', '=', True)]).to_pandas(types_mapper=pd.ArrowDtype)
    series = build_main_sample_series(positions, prices)
    axis_label = {'time': '实际分钟', 'money': '成交额', 'gk_money': 'GK×成交额'}[axis]
    method_label = {'log_interpolate': '分钟内插值', 'minute_close_reset': '分钟末清零'}[sampling_method]
    title = f'{underlying_code} {axis_label} {N}min（{method_label}）'
    plot_notebook = json.loads((method_dir / 'c02_SamplingExecution.ipynb').read_text(encoding='utf8'))
    plot_source = next(''.join(cell['source']) for cell in plot_notebook['cells']
                       if cell.get('id') == 'sampling-comparison-definition')
    context = dict(label=f'{underlying_code} · N={N} · {axis_label} · {method_label}',
        parameters=dict(underlying_code=underlying_code, N=N, axis=axis,
                        quantity_scope=quantity_scope, sampling_method=sampling_method),
        positions_path=position_path.relative_to(root).as_posix(), prices_path=price_path.relative_to(root).as_posix(),
        upstream_path=upstream_path.relative_to(root).as_posix(),
        positions_identity=json.loads(pq.read_schema(position_path).metadata[b'demo_identity']),
        prices_identity=json.loads(pq.read_schema(price_path).metadata[b'demo_identity']),
        plot_source_sha256=hashlib.sha256(plot_source.encode()).hexdigest())
    return series, title, context


In [ ]:
def copy_sampling_image_to_clipboard(png: bytes) -> None:
    """将 PNG 的原始像素复制到本地 Windows 图像剪贴板。"""
    import ctypes
    import io
    import os
    from ctypes import wintypes
    from PIL import Image

    if os.name != 'nt':
        raise RuntimeError('复制图像需要本地 Windows 内核')
    if not png:
        raise ValueError('当前没有可复制的图像')

    # BMP 去掉 14 字节文件头即为 DIB；不调整尺寸，也不改写已保存的 PNG。
    with Image.open(io.BytesIO(png)) as image:
        bitmap = io.BytesIO()
        image.convert('RGB').save(bitmap, format='BMP')  # 现有图像背景不透明
    dib = bitmap.getvalue()[14:]
    user32 = ctypes.WinDLL('user32', use_last_error=True)
    kernel32 = ctypes.WinDLL('kernel32', use_last_error=True)

    # 显式声明 64 位句柄和指针类型，避免默认整数返回值截断内存地址。
    signatures = [
        (kernel32.GlobalAlloc, [wintypes.UINT, ctypes.c_size_t], wintypes.HGLOBAL),
        (kernel32.GlobalLock, [wintypes.HGLOBAL], ctypes.c_void_p),
        (kernel32.GlobalUnlock, [wintypes.HGLOBAL], wintypes.BOOL),
        (kernel32.GlobalFree, [wintypes.HGLOBAL], wintypes.HGLOBAL),
        (user32.CreateWindowExW, [wintypes.DWORD, wintypes.LPCWSTR, wintypes.LPCWSTR, wintypes.DWORD,
            ctypes.c_int, ctypes.c_int, ctypes.c_int, ctypes.c_int, wintypes.HWND, wintypes.HMENU,
            wintypes.HINSTANCE, ctypes.c_void_p], wintypes.HWND),
        (user32.DestroyWindow, [wintypes.HWND], wintypes.BOOL),
        (user32.OpenClipboard, [wintypes.HWND], wintypes.BOOL),
        (user32.EmptyClipboard, [], wintypes.BOOL),
        (user32.SetClipboardData, [wintypes.UINT, wintypes.HANDLE], wintypes.HANDLE),
        (user32.CloseClipboard, [], wintypes.BOOL),
    ]
    for function, arguments, return_type in signatures:
        function.argtypes, function.restype = arguments, return_type

    # 先准备完整图片内存，成功打开剪贴板后才替换其中内容。
    memory, owner, clipboard_open = None, None, False
    try:
        memory = kernel32.GlobalAlloc(0x0002, len(dib))  # GMEM_MOVEABLE
        if not memory:
            raise ctypes.WinError(ctypes.get_last_error())
        pointer = kernel32.GlobalLock(memory)
        if not pointer:
            raise ctypes.WinError(ctypes.get_last_error())
        try:
            ctypes.memmove(pointer, dib, len(dib))
        finally:
            kernel32.GlobalUnlock(memory)  # 返回 0 也可能表示已正常解锁

        # 临时消息窗口属于当前进程；空 owner 会导致写入剪贴板失败。
        owner = user32.CreateWindowExW(0, 'STATIC', '', 0, 0, 0, 0, 0,
            wintypes.HWND(-3), None, None, None)  # HWND_MESSAGE，不显示窗口
        if not owner:
            raise ctypes.WinError(ctypes.get_last_error())
        if not user32.OpenClipboard(owner):
            raise OSError('剪贴板正被其他程序占用，请再次点击复制')
        clipboard_open = True
        if not user32.EmptyClipboard():
            raise ctypes.WinError(ctypes.get_last_error())
        if not user32.SetClipboardData(8, memory):  # CF_DIB，可粘贴为图片
            raise ctypes.WinError(ctypes.get_last_error())
        memory = None  # 写入成功后，内存所有权交给系统
    finally:
        if clipboard_open:
            user32.CloseClipboard()
        if memory:
            kernel32.GlobalFree(memory)  # 仅释放尚未交给系统的内存
        if owner:
            user32.DestroyWindow(owner)


In [ ]:
def display_sampling_demo_figures(*, project_root: str | Path, notebook_path: str | Path | None = None,
                                  underlying_code: str = 'RB', N: int = 10, axis: str = 'time',
                                  quantity_scope: str = 'all_contracts',
                                  sampling_method: str = 'log_interpolate', plot_kind: str = 'price') -> None:
    """在当前单元格显示参数选择器和一张图；再次调用会创建独立输出。"""
    import ipywidgets as widgets
    from IPython.display import display

    # 每次调用独立读取已经保存的图像，不触发采样或 GH 拟合。
    root = Path(project_root).resolve()
    if notebook_path is None:
        notebook_path = root / 'R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution.ipynb'
    image_catalog = read_sampling_comparison_images(project_root=root, notebook_path=notebook_path,
        quantity_scope=quantity_scope)  # 固定数量口径，五项控件只选择图像配置
    configurations = list(image_catalog)
    initial = (underlying_code, N, axis, sampling_method)
    if initial not in image_catalog:
        raise ValueError('初始品种、N、轴、采样方式对应的图像尚未生成')

    # 四项采样参数和图形类型分别选择；新增已保存的方式或图形会进入候选项。
    varieties = list(dict.fromkeys(key[0] for key in configurations))
    granularities = list(dict.fromkeys(key[1] for key in configurations))
    axes = list(dict.fromkeys(key[2] for key in configurations))
    methods = list(dict.fromkeys(key[3] for key in configurations))
    kinds = list(dict.fromkeys(kind for images in image_catalog.values() for kind in images))
    axis_labels = {'time': '实际分钟', 'money': '成交额', 'gk_money': 'GK×成交额'}
    method_labels = {'log_interpolate': '分钟内插值', 'minute_close_reset': '分钟末清零'}
    kind_keys = {'价格序列': 'price', 'GH 拟合': 'gh'}
    kind_labels = {'价格序列': '价格折线图', 'GH 拟合': 'GH 拟合图'}
    kinds_by_key = {kind_keys.get(kind, kind): kind for kind in kinds}
    if plot_kind not in kinds_by_key:
        raise ValueError('初始图形类型未提供')
    variety_choice = widgets.Dropdown(options=varieties, value=underlying_code, description='品种',
        layout=widgets.Layout(width='90px', height='28px', min_height='28px', flex='0 0 auto'), style={'description_width': 'initial'})
    N_choice = widgets.Dropdown(options=granularities, value=N, description='N',
        layout=widgets.Layout(width='70px', height='28px', min_height='28px', flex='0 0 auto'), style={'description_width': 'initial'})
    axis_choice = widgets.Dropdown(options=[(axis_labels.get(value, value), value) for value in axes],
        value=axis, description='轴', layout=widgets.Layout(width='145px', height='28px', min_height='28px', flex='0 0 auto'), style={'description_width': 'initial'})
    method_choice = widgets.Dropdown(options=[(method_labels.get(value, value), value) for value in methods],
        value=sampling_method, description='采样方式', layout=widgets.Layout(width='180px', height='28px', min_height='28px', flex='0 0 auto'),
        style={'description_width': 'initial'})
    kind_choice = widgets.Dropdown(options=[(kind_labels.get(kind, kind), key) for key, kind in kinds_by_key.items()],
        value=plot_kind, description='图形', layout=widgets.Layout(width='155px', height='28px', min_height='28px', flex='0 0 auto'), style={'description_width': 'initial'})

    # 始终复用这一个 Image 组件，切换参数时替换其 PNG 字节。
    picture = widgets.Image(format='png', layout=widgets.Layout(width='100%', height='auto'))
    message = widgets.HTML(layout=widgets.Layout(margin='0'))
    copy_button = widgets.Button(description='复制图像', icon='copy', tooltip='复制当前图片的原始分辨率',
        layout=widgets.Layout(width='100px', height='28px', flex='0 0 auto'), style={'font_size': '13px'})
    compact_style = widgets.HTML(value='''<style>
        .sampling-image-controls .widget-label {font-size:13px!important; line-height:26px!important;}
        .sampling-image-controls select {font-size:13px!important; height:26px!important; min-height:26px!important;}
        .sampling-image-controls button {font-size:13px!important; line-height:24px!important; padding:0 6px!important;}
    </style>''', layout=widgets.Layout(display='none'))

    def update_image(change=None):
        key = (variety_choice.value, N_choice.value, axis_choice.value, method_choice.value)
        kind = kinds_by_key[kind_choice.value]
        content = image_catalog.get(key, {}).get(kind)
        picture.value = b'' if content is None else content
        message.value = '该参数组合的图像尚未生成。' if content is None else ''
        copy_button.disabled = content is None

    # 复制按钮读取此刻选中的 PNG；成功与失败信息直接显示在当前输出中。
    def copy_current_image(button):
        from html import escape
        copy_button.disabled = True
        try:
            copy_sampling_image_to_clipboard(bytes(picture.value))
        except Exception as error:
            message.value = f'<span style="font-size:13px;color:#b3261e">复制失败：{escape(str(error))}</span>'
        else:
            message.value = '<span style="font-size:13px">已复制图像</span>'
        finally:
            copy_button.disabled = not bool(picture.value)

    # 事件和状态都归本次调用；其他单元格的选择不会改变这一张图。
    controls = [variety_choice, N_choice, axis_choice, method_choice, kind_choice]
    for control in controls:
        control.observe(update_image, names='value')
    copy_button.on_click(copy_current_image)
    update_image()
    toolbar = widgets.HBox([*controls, copy_button],
        layout=widgets.Layout(flex_flow='row wrap', align_items='center', margin='0', grid_gap='4px'))
    toolbar.add_class('sampling-image-controls')
    display(widgets.VBox([toolbar, message, picture, compact_style], layout=widgets.Layout(width='100%')))


def read_sampling_comparison_images(*, project_root: str | Path, notebook_path: str | Path,
                                    configuration: tuple | None = None, quantity_scope: str | None = None,
                                    include_metadata: bool = False) -> dict:
    """读取 Notebook 内嵌的价格/GH 图，并核对其配置、数据身份与绘图定义。"""
    root = Path(project_root).resolve()
    notebook_path = Path(notebook_path).resolve()
    book = json.loads(notebook_path.read_text(encoding='utf8'))
    plot_source = next(''.join(cell['source']) for cell in book['cells'] if cell.get('id') == 'sampling-comparison-definition')
    plot_digest = hashlib.sha256(plot_source.encode()).hexdigest()
    image_groups, checked_contexts, current_sources, current_upstreams = {}, {}, {}, {}

    # 内嵌图像携带原有来源身份；每个配置只核对一次文件 footer。
    for output in book['metadata'].get('sampling_comparison_images', []):
        context = output.get('metadata', {}).get('sampling_comparison')
        if context is None:
            continue
        parameters = context['parameters']
        underlying = parameters['underlying_code']
        config_key = (underlying, int(parameters['N']), parameters['axis'], parameters['sampling_method'])
        if configuration is not None and config_key != configuration:
            continue
        if quantity_scope is not None and parameters['quantity_scope'] != quantity_scope:
            continue
        label = context['label']
        kind = context['figure_kind']
        if context['plot_source_sha256'] != plot_digest:
            raise RuntimeError(f'{label} 的绘图定义已变化，请重新绘图')
        context_key = (context['positions_path'], context['prices_path'])
        identities = (context['positions_identity'], context['prices_identity'])
        if context_key in checked_contexts:
            if checked_contexts[context_key] != identities:
                raise RuntimeError(f'{label} 的价格图与 GH 图数据身份不一致')
        else:
            for key in ('positions', 'prices'):
                path = root / context[key + '_path']
                identity = json.loads(pq.read_schema(path).metadata[b'demo_identity'])
                if identity != context[key + '_identity']:
                    raise RuntimeError(f'{label} 的数据已变化，请重新绘图')
                if underlying not in current_upstreams:
                    upstream_path = root / context['upstream_path']
                    current_upstreams[underlying] = json.loads(pq.read_schema(upstream_path).metadata[b'demo_identity'])
                if identity['upstream_demo_identity'] != current_upstreams[underlying]:
                    raise RuntimeError(f'{label} 的复权输入已变化，请重新生成数据和图像')
                if underlying not in current_sources:
                    current_sources[underlying] = sampling_demo_identity(project_root=root,
                        producer_notebook=root / identity['producer_notebook'],
                        upstream_identity=identity['upstream_demo_identity'], parameters=identity['parameters'],
                        calibration=identity['calibration'], scope=identity['scope'])
                current = current_sources[underlying]
                if any(current[name] != identity[name] for name in
                       ('dependency_method_source_sha256', 'dependency_source_sha256')):
                    raise RuntimeError(f'{label} 的采样定义已变化，请重新生成数据和图像')
            checked_contexts[context_key] = identities
        content = output.get('data', {}).get('image/png')
        if content is None:
            raise RuntimeError(f'{label} 的 {kind} 图像未保存')
        config_key = (underlying, int(parameters['N']), parameters['axis'], parameters['sampling_method'])
        group = image_groups.setdefault(config_key, {})
        if kind in group:
            raise RuntimeError(f'{label} 的 {kind} 图像重复')
        png = base64.b64decode(''.join(content) if isinstance(content, list) else content)
        group[kind] = (png, context) if include_metadata else png

    # 每个候选配置必须同时具有价格图和 GH 图，不能静默漏掉一种结果。
    if not image_groups and configuration is not None:
        return {}
    if not image_groups:
        raise RuntimeError('Notebook 尚未保存可比较的采样图像')
    if any(not {'价格序列', 'GH 拟合'}.issubset(group) for group in image_groups.values()):
        raise RuntimeError('有配置缺少价格图或 GH 图，请补齐绘图结果')
    return image_groups


## 固定分界的完整序列 demo

<a id="fixed-boundary-demo"></a>

下面参数每次选择一个品种、$N$、轴、成交额范围和采样方式。品种可选 CU、RB，$N$ 可选 10、15、30、60，轴可选 `time`、`money` 或 `gk_money`，采样方式可选 `log_interpolate` 或 `minute_close_reset`。默认为 RB、$N=10$、全部合约成交额及分钟内插值。

请求范围为 2010-01-01 至 2026-09-30，实际分钟以上游文件为准。初始单位使用 `trading_date < 2025-01-01` 的全部记录校准，$t$ 取该训练期最后一个实际分钟末端，`K=None`，因此输出包含两侧完整序列。文件名分别写明训练范围 `train20100101-20241231` 和测试范围 `test20250101-20260930`。

参数单元格确定输入和输出路径，随后计算并保存各合约采样价格到 `c02_SamplingExecution_DemoData/c02_SamplingExecution_..._fixed_demo.parquet`，展示单位校准结果与主力采样序列。用于绘图的位置文件由[采样位置 Notebook](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c01_SamplingPositions.ipynb)以相同配置保存；绘图读取两份文件并按 `sample_id` 关联。


`demo_reuse_existing=True` 时先核对保存结果；位置和价格的上游、参数、生成定义、数值环境及内容摘要一致，就直接读取。该分支不准备分钟轴与报价，不重新校准或采样。设为 `False` 可显式重算。


In [ ]:
# 选择一个业务配置，修改这些参数后运行对应 demo。
demo_underlying_code = 'RB'  # 品种：CU 或 RB
demo_N = 10  # 候选分钟数：10、15、30、60
demo_axis_name = 'money'  # time、money 或 gk_money
demo_quantity_scope = 'all_contracts'  # 全部合约合计；也支持 main_contract
demo_sampling_method = 'log_interpolate'  # 分钟内插值；也支持 minute_close_reset
demo_test_start_date = date(2025, 1, 1)  # 按 trading_date 划分初始校准训练期
demo_range_token = 'train20100101-20241231_test20250101-20260930'
demo_reuse_existing = True  # 条件一致时复用；False 显式重算
demo_threads = 8  # 数值环境中的并行线程数
numba.set_num_threads(min(demo_threads, numba.config.NUMBA_NUM_THREADS))

# 用完整文件名指定复权输入和所属输出，训练／测试范围分别写入名称。
demo_upstream_notebook = candidate_root / 'R04_Research/a01_Methods/b02_MainContinuousAdjustment/c01_MainContinuousAdjustment.ipynb'
demo_upstream_path = (
    demo_upstream_notebook.parent / 'c01_MainContinuousAdjustment_DemoData'
    / f'c01_MainContinuousAdjustment_{demo_underlying_code}_{demo_range_token}_ratio1.10_log_common_demo.parquet'
)
demo_method_notebook = candidate_root / 'R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution.ipynb'
demo_output_path = (
    demo_method_notebook.parent / 'c02_SamplingExecution_DemoData'
    / f'{demo_method_notebook.stem}_{demo_underlying_code}_{demo_range_token}_'
      f'N{demo_N}_{demo_axis_name}_{demo_quantity_scope}_{demo_sampling_method}_fixed_demo.parquet'
)

# 固定序列复用时同时读取同配置的位置结果。
demo_position_notebook = demo_method_notebook.with_name('c01_SamplingPositions.ipynb')
demo_position_path = (demo_position_notebook.parent / 'c01_SamplingPositions_DemoData'
    / f'{demo_position_notebook.stem}_{demo_underlying_code}_{demo_range_token}_'
      f'N{demo_N}_{demo_axis_name}_{demo_quantity_scope}_{demo_sampling_method}_fixed_demo.parquet')


In [ ]:
# 在完整输入准备之前判断位置和价格能否共同复用。
demo_requested_parameters = dict(N=demo_N, axis=demo_axis_name, quantity_scope=demo_quantity_scope,
    sampling_method=demo_sampling_method, execution_mode='fixed', K=None)
demo_existing_identity = read_reusable_sampling_identity(demo_output_path, project_root=candidate_root,
    producer_notebook=demo_method_notebook, upstream_path=demo_upstream_path,
    underlying_code=demo_underlying_code, test_start_date=demo_test_start_date,
    parameters=demo_requested_parameters, reuse_existing=demo_reuse_existing)
demo_position_identity = read_reusable_sampling_identity(demo_position_path, project_root=candidate_root,
    producer_notebook=demo_position_notebook, upstream_path=demo_upstream_path,
    underlying_code=demo_underlying_code, test_start_date=demo_test_start_date,
    parameters=demo_requested_parameters, reuse_existing=demo_reuse_existing) if demo_existing_identity else None
demo_axis_minutes = demo_quotes = demo_prepared_axis = None
if (demo_existing_identity is not None and demo_position_identity is not None
        and demo_existing_identity['calibration'] == demo_position_identity['calibration']
        and demo_existing_identity['parameters']['t'] == demo_position_identity['parameters']['t']):
    demo_upstream_identity = demo_existing_identity['upstream_demo_identity']
    demo_calibration = demo_existing_identity['calibration']
    demo_parameters = demo_existing_identity['parameters']
    demo_t = pd.Timestamp(demo_parameters['t'])
    demo_positions = pq.read_table(demo_position_path).to_pandas(types_mapper=pd.ArrowDtype)
    demo_save = {'identity': demo_existing_identity, 'preserved_existing': True}
    print('复用已有固定序列；跳过分钟轴、报价准备、初始校准和采样。')
else:
    # 核对固定复权输入，再准备实际分钟采样轴。
    demo_upstream_identity = verify_adjusted_demo(demo_upstream_path, producer_notebook=demo_upstream_notebook,
        project_root=candidate_root, underlying_code=demo_underlying_code, test_start_date=demo_test_start_date)
    demo_axis_minutes, demo_quotes = prepare_sampling_input(demo_upstream_path, axis=demo_axis_name, quantity_scope=demo_quantity_scope)

    # 只按初始训练期校准 a，再准备可复用的累计轴。
    demo_calibration = calibrate_sampling_unit(demo_axis_minutes, N=demo_N, test_start_date=demo_test_start_date)
    demo_prepared_axis = prepare_sampling_axis(demo_axis_minutes, a=demo_calibration['a'], sampling_method=demo_sampling_method)

    # 固定分界取训练末实际分钟，返回两侧完整序列。
    demo_t = demo_axis_minutes.loc[demo_axis_minutes['trading_date'] < demo_test_start_date, 'bar_at'].iloc[-1]
    demo_positions = generate_sampling_positions(demo_prepared_axis, t=demo_t, K=None)  # K=None，不限制每侧点数
    demo_parameters = dict(N=demo_N, axis=demo_axis_name, quantity_scope=demo_quantity_scope,
                           sampling_method=demo_sampling_method, execution_mode='fixed', t=str(demo_t), K=None)

    # 记录这个配置的生成条件，保存后复读验收。
    demo_identity = sampling_demo_identity(project_root=candidate_root, producer_notebook=demo_method_notebook,
        upstream_identity=demo_upstream_identity, parameters=demo_parameters, calibration=demo_calibration,
        scope=demo_upstream_identity['scope'])
    demo_save = save_sampling_demo(iter_sampled_price_batches(demo_quotes, demo_prepared_axis, t=demo_t, K=None),
                                   demo_path=demo_output_path, demo_identity=demo_identity)
demo_main_prices = pq.read_table(demo_output_path, filters=[('is_main', '=', True)]).to_pandas(types_mapper=pd.ArrowDtype)
demo_main_series = build_main_sample_series(demo_positions, demo_main_prices)

# 只给展示副本加中文表头，计算和文件仍保留原字段。
display(pd.DataFrame([demo_calibration]).rename(columns=EXECUTION_COLUMN_LABELS))
display(demo_main_series.head().rename(columns=EXECUTION_COLUMN_LABELS))


## 逐分钟滚动分界 demo

<a id="rolling-boundary-demo"></a>

下面将初始测试期的前 100 个实际分钟末端依次作为 $t$。某分钟 close 已知后，该分钟进入这个分界的训练侧；测试侧从下一实际分钟开始。每个分界分别返回过去和未来最多 $K=32$ 点，过去的最后一点为 $t$ 的 close，范围不足时保留实际可得结果。

滚动复用固定分界 demo 已准备的报价、采样轴和单位 $a$。修改 `demo_rolling_t` 可以选择其他递增分界序列，修改 `demo_K` 可以改变每侧点数；初始校准范围和输入复权价格保持固定。

`iter_sampled_price_batches` 逐批生成各分界的全部合约价格，保存函数直接消费这些批次。输出文件以 `rolling_first100_K32` 标明本示范的范围和点数，末尾预览前 20 行。


滚动结果复用沿用同一开关；数量、K、上游、固定校准值和生成定义须一致。对应文件尚不存在时首次计算，保存后可复用。


In [ ]:
# 选择滚动分界数量与每侧点数，复用固定 a。
demo_K = 32  # 每侧最多 32 点，含训练末 t 点
demo_rolling_count = 100  # 初始测试期前 100 个实际分钟末端
demo_rolling_path = (demo_method_notebook.parent / 'c02_SamplingExecution_DemoData'
    / f'{demo_method_notebook.stem}_{demo_underlying_code}_{demo_range_token}_'
      f'N{demo_N}_{demo_axis_name}_{demo_quantity_scope}_{demo_sampling_method}_'
      f'rolling_first{demo_rolling_count}_K{demo_K}_demo.parquet')
demo_rolling_parameters = {**{key: value for key, value in demo_parameters.items() if key != 't'},
    'execution_mode': 'rolling', 'K': demo_K, 'rolling_count': demo_rolling_count}

# 滚动结果已保存且条件相同，就直接读取，不为预览重新准备完整分钟输入。
demo_rolling_existing = read_reusable_sampling_identity(demo_rolling_path, project_root=candidate_root,
    producer_notebook=demo_method_notebook, upstream_path=demo_upstream_path,
    underlying_code=demo_underlying_code, test_start_date=demo_test_start_date,
    parameters=demo_rolling_parameters, reuse_existing=demo_reuse_existing)
if demo_rolling_existing is not None:
    demo_rolling_t = pd.DatetimeIndex(demo_rolling_existing['parameters']['t'])
    demo_rolling_save = {'identity': demo_rolling_existing, 'preserved_existing': True}
    print('复用已有滚动序列；跳过报价准备与滚动采样。')
else:
    # 固定序列走了复用分支时，首次滚动计算才准备轴与报价，保留原 a。
    if demo_axis_minutes is None:
        verify_adjusted_demo(demo_upstream_path, producer_notebook=demo_upstream_notebook,
            project_root=candidate_root, underlying_code=demo_underlying_code, test_start_date=demo_test_start_date)
        demo_axis_minutes, demo_quotes = prepare_sampling_input(demo_upstream_path,
            axis=demo_axis_name, quantity_scope=demo_quantity_scope)
        demo_prepared_axis = prepare_sampling_axis(demo_axis_minutes, a=demo_calibration['a'],
            sampling_method=demo_sampling_method)
    demo_rolling_t = demo_axis_minutes.loc[demo_axis_minutes['trading_date'] >= demo_test_start_date, 'bar_at'].iloc[:demo_rolling_count]
    demo_rolling_identity = sampling_demo_identity(project_root=candidate_root, producer_notebook=demo_method_notebook,
        upstream_identity=demo_upstream_identity, parameters={**demo_rolling_parameters, 't': [str(value) for value in demo_rolling_t]},
        calibration=demo_calibration, scope=demo_upstream_identity['scope'])
    demo_rolling_save = save_sampling_demo(iter_sampled_price_batches(demo_quotes, demo_prepared_axis,
        t=demo_rolling_t, K=demo_K), demo_path=demo_rolling_path, demo_identity=demo_rolling_identity)

display(pq.read_table(demo_rolling_path).slice(0, 20).to_pandas(types_mapper=pd.ArrowDtype).rename(columns=EXECUTION_COLUMN_LABELS))


## 48 组价格数据 demo

<a id="saved-价格-demos"></a>

各配置独立生成，使用固定分界和完整序列（`K=None`）。时间轴累计实际分钟；成交额和 GK×成交额轴使用全部合约成交额。训练交易日为 2010-01-01 至 2024-12-31，测试交易日为 2025-01-01 至 2026-09-30；实际分钟由 b02 输入决定。

| 品种 | N | 采样轴 | 采样方式 | 价格文件 |
| --- | ---: | --- | --- | --- |
| CU | 10 | 实际分钟 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N10_time_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 10 | 实际分钟 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N10_time_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 10 | 成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N10_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 10 | 成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N10_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 10 | GK×成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N10_gk_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 10 | GK×成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N10_gk_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 15 | 实际分钟 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N15_time_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 15 | 实际分钟 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N15_time_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 15 | 成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N15_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 15 | 成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N15_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 15 | GK×成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N15_gk_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 15 | GK×成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N15_gk_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 30 | 实际分钟 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N30_time_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 30 | 实际分钟 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N30_time_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 30 | 成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N30_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 30 | 成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N30_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 30 | GK×成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N30_gk_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 30 | GK×成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N30_gk_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 60 | 实际分钟 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N60_time_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 60 | 实际分钟 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N60_time_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 60 | 成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N60_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 60 | 成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N60_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| CU | 60 | GK×成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N60_gk_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| CU | 60 | GK×成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_CU_train20100101-20241231_test20250101-20260930_N60_gk_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 10 | 实际分钟 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N10_time_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 10 | 实际分钟 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N10_time_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 10 | 成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N10_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 10 | 成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N10_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 10 | GK×成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N10_gk_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 10 | GK×成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N10_gk_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 15 | 实际分钟 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N15_time_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 15 | 实际分钟 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N15_time_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 15 | 成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N15_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 15 | 成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N15_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 15 | GK×成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N15_gk_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 15 | GK×成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N15_gk_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 30 | 实际分钟 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N30_time_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 30 | 实际分钟 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N30_time_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 30 | 成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N30_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 30 | 成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N30_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 30 | GK×成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N30_gk_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 30 | GK×成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N30_gk_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 60 | 实际分钟 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N60_time_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 60 | 实际分钟 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N60_time_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 60 | 成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N60_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 60 | 成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N60_money_all_contracts_minute_close_reset_fixed_demo.parquet) |
| RB | 60 | GK×成交额 | 分钟内插值 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N60_gk_money_all_contracts_log_interpolate_fixed_demo.parquet) |
| RB | 60 | GK×成交额 | 分钟末清零 | [价格 Parquet](E:/Latitude_Analytics_v2/R04_Research/a01_Methods/b03_Sampling/c02_SamplingExecution_DemoData/c02_SamplingExecution_RB_train20100101-20241231_test20250101-20260930_N60_gk_money_all_contracts_minute_close_reset_fixed_demo.parquet) |


## 主力价格序列与 GH 拟合

<a id="main-price-and-gh"></a>

比较范围为 CU、RB × $N=10,15,30,60$ × 实际分钟、成交额、GK×成交额 × 两种采样方式，共 48 组。每组使用采样点的主力价格，价格序列和 GH 分布分别占一张独立图。

价格图绘制 log 主力价格，横轴按采样顺序排列，以稀疏交易日刻度显示时间跨度。价格缺失的点保留为空，曲线在缺口处断开。

对一个分界，先将训练侧与测试侧按时间连接，再计算一次相邻点的 log 收益率：

$$r_j=\ln P_j-\ln P_{j-1}.$$

首个点的收益率为空，训练／测试分界两侧的相邻点参与差分。缺价格直接使相关差分为空，不先删除缺价点再跨缺口计算；滚动时分别在各 $t$ 的序列内差分，不跨不同分界的窗口。

分布图使用非空 log 收益率绘制白底黑边的密度直方图，并以蓝色曲线绘制广义双曲分布（GH）拟合。拟合默认开启，使用该序列全部非空收益率；横纵坐标默认按完整收益率范围及密度自动缩放，保留峰顶；显式传入 `xlim`、`ylim` 时只调整显示范围。拟合失败明确报错。


## 单图交互选择

<a id="interactive-image-comparison"></a>

运行下面单元格，即在本单元格下方出现品种、N、轴、采样方式和图形类型五个选择控件。选择后只呈现一张对应图片；切换参数直接替换这一张图。控件使用紧凑尺寸，窄窗口自动换行。点击“复制图像”将当前图片的原始分辨率复制到本地 Windows 剪贴板，可直接粘贴到其他软件；复制成功或失败会在图像上方显示。

候选配置覆盖 CU、RB、N=10/15/30/60、实际分钟/成交额/GK×成交额和两种采样方式，图形可选价格折线图或 GH 拟合图。选项来自已保存的图像；新增采样方式或图形后，其选项也可进入选择器。交互选择不触发采样或拟合。

`display_sampling_demo_figures(project_root=candidate_root)` 是可直接调用的函数，调用后自行显示选择器与单张图，不需要另外调用 `display()`。默认显示 RB、N=10、实际分钟轴、分钟内插值的价格折线图；也可通过 `underlying_code`、`N`、`axis`、`sampling_method`、`plot_kind` 指定初始选择，`plot_kind` 的当前取值为 `price` 或 `gh`。

需要比较多张图时，在新的代码单元格中再次调用同一函数。每次调用创建独立选择器，各单元格的选项和图像互不影响。

96 张已生成图片及来源信息内嵌在本 Notebook 中，选择器直接读取。图像来源与当前数据或绘图定义不一致时明确报错，交互切换不启动重新计算。可调用的主力序列读取、价格绘图和 GH 拟合方法保留在定义单元格中。


In [ ]:
# 直接在本单元格下方显示五项选择控件与一张图。
display_sampling_demo_figures(project_root=candidate_root)